# Grid Visualizations Comparison Notebook

This notebook produces animated video GIFs for:
1. **TD Run**
2. **MC Run**
3. **Exact E Run (Seed 1)**
4. **Exact E Run (Seed 2)**

For each of these runs, it loads complete metrics (`LIGHT_METRICS=False`) and produces a video GIF of:
- **State Distribution Grid** (`state_dist_grid` / `stat_dist`)
- **True Value Grid** (`V_grid` / `value_grid`)
- **Predicted Value Grid** (`nn_grid`)
- **Signed Value Error Grid** ($v - V$, positive = overestimation)


In [ ]:
import os
import sys
import numpy as np
import matplotlib.pyplot as plt
import matplotlib.animation as animation
from IPython.display import HTML, display

# Ensure project root is in sys.path
if '..' not in sys.path:
    sys.path.insert(0, '..')

from core.utils import load_run_data_from_path, load_run_data


# ==============================================================================
# Input Configuration for Runs
# Set directory paths or (run_folder, env_name) along with seed index for each run.
# ==============================================================================

RUNS_CONFIG = {
    "TD": {
        "name": "TD Run",
        "path": "results/ppo/exact_td/20260914_162454/Eightrooms",
        "run_folder": "ppo/exact_td/20260914_162454",
        "env_name": "Eightrooms",
        "seed_idx": 0,
        "gif_output": "figures/td_run_grid_vis.gif"
    },
    "MC": {
        "name": "MC Run",
        "path": "results/ppo/exact_mc/20260914_225408/Eightrooms",
        "run_folder": "ppo/exact_mc/20260914_225408",
        "env_name": "Eightrooms",
        "seed_idx": 0,
        "gif_output": "figures/mc_run_grid_vis.gif"
    },

    "MC_seed_2": {
        "name": "MC Run 2",
        "path": "results/ppo/exact_mc/20260914_163400/Eightrooms",
        "run_folder": "ppo/exact_mc/20260914_163400",
        "env_name": "Eightrooms",
        "seed_idx": 0,
        "gif_output": "figures/mc_run2_grid_vis.gif"
    },    
    
    "E_seed1": {
        "name": "Exact E Run (Seed 1)",
        "path": "results/ppo/exact_E/20260914_230230/Eightrooms",
        "run_folder": "ppo/exact_E/20260914_230230",
        "env_name": "Eightrooms",
        "seed_idx": 0,
        "gif_output": "figures/E_seed_1_vis.gif"
    },
    "E_seed2": {
        "name": "Exact E Run (Seed 2)",
        "path": "results/ppo/exact_E/20260914_161700/Eightrooms",
        "run_folder": "ppo/exact_E/20260914_161700",
        "env_name": "Eightrooms",
        "seed_idx": 0,
        "gif_output": "figures/exact_E_seed2_grid_vis.gif"
    },

    "E_lambda": {
        "name": "Exact Eλ Run",
        "path": "results/ppo/exact_E_lambda//20260914_220415/Eightrooms",
        "run_folder": "ppo/exact_E_lambda//20260914_220415",
        "env_name": "Eightrooms",
        "seed_idx": 0,
        "gif_output": "figures/exact_E_lambda_grid.gif"
    }
}

# E seed 1, MC seed 1, and E lambda all have same settings and seed: Config: {"LIGHT_METRICS": "False", "SEED": 6, "ACTOR_LR": 0.0003, "LR": 0.005, "VALUE_LAMBDA" : 0.5}
# 

In [2]:
from matplotlib import colors
def generate_and_save_grid_gif(run_info, save_gif=True, fps=5, max_frames=50, display_inline=True):
    """
    Loads run metrics and generates a 1x4 animation comparing:
    1. State Distribution Grid
    2. True Value Grid (V)
    3. Predicted Value Grid (v)
    4. Signed Value Error Grid (v - V, overestimation > 0)

    Parameters:
    - run_info (dict): Dict containing 'name', 'path', 'seed_idx', and 'gif_output'.
    - save_gif (bool): Whether to export the animation as a GIF file.
    - fps (int): Frames per second for the output GIF.
    - max_frames (int): Maximum frames to include (sub-sampled for efficiency).
    - display_inline (bool): Whether to render interactive JS HTML animation in notebook.
    """
    run_name = run_info.get("name", "Run")
    seed_idx = run_info.get("seed_idx", 0)
    gif_path = run_info.get("gif_output", f"{run_name.lower().replace(' ', '_')}.gif")
    
    path = run_info.get("path")
    loaded = False
    if path:
        candidate_paths = [path, os.path.join("..", path), os.path.join("results", path)]
        for cand in candidate_paths:
            if os.path.exists(cand):
                config, metrics = load_run_data_from_path(cand)
                loaded = True
                break
                
    if not loaded:
        run_folder = run_info.get("run_folder")
        env_name = run_info.get("env_name")
        if run_folder and env_name:
            config, metrics = load_run_data(run_folder, env_name)
        else:
            raise FileNotFoundError(f"Could not locate run data for {run_name} at path '{path}'")

    # Extract required grid arrays
    state_dist = metrics.get("state_dist_grid", metrics.get("stat_dist"))
    v_true = metrics.get("V_grid", metrics.get("value_grid"))
    v_pred = metrics.get("nn_grid")

    if state_dist is None or v_true is None or v_pred is None:
        raise ValueError(
            f"Missing required grid metrics for {run_name}. "
            f"Ensure run has complete metrics (LIGHT_METRICS=False)."
        )

    # Index seed if 4D tensor (seeds, updates, height, width)
    if state_dist.ndim == 4:
        state_dist = state_dist[seed_idx]
    if v_true.ndim == 4:
        v_true = v_true[seed_idx]
    if v_pred.ndim == 4:
        v_pred = v_pred[seed_idx]

    num_updates = len(state_dist)

    # Broadcast v_true if static (2D)
    if v_true.ndim == 2:
        v_true = np.tile(v_true[None, :, :], (num_updates, 1, 1))

    # Subsample frames if length exceeds max_frames
    if max_frames and num_updates > max_frames:
        frame_indices = np.linspace(0, num_updates - 1, max_frames, dtype=int)
        state_dist = state_dist[frame_indices]
        v_true = v_true[frame_indices]
        v_pred = v_pred[frame_indices]
        num_updates = len(frame_indices)

    # Compute Signed Value Error: v_pred - v_true (overestimation is positive)
    signed_error = v_pred - v_true

    # Color limits for True & Predicted Value Grids
    v_min = float(min(np.min(v_true), np.min(v_pred)))
    v_max = float(max(np.max(v_true), np.max(v_pred)))
    if v_min == v_max:
        v_min, v_max = v_min - 1.0, v_max + 1.0

    # Independent symmetric color limits for Signed Value Error (centered at 0)
    err_abs_max = float(np.max(np.abs(signed_error)))
    if err_abs_max == 0:
        err_abs_max = 1.0

    fig, (ax1, ax2, ax3, ax4) = plt.subplots(1, 4, figsize=(20, 4.5))
    fig.suptitle(f"{run_name} (Seed {seed_idx})", fontsize=15, fontweight='bold', y=1.03)

    # 1. State Distribution Grid
    im1 = ax1.imshow(state_dist[0], cmap="viridis", animated=True)
    ax1.set_title("State Distribution Grid", fontsize=12)
    fig.colorbar(im1, ax=ax1, fraction=0.046, pad=0.04)

    # 2. True Value Grid
    im2 = ax2.imshow(v_true[0], cmap="RdBu_r", vmin=v_min, vmax=v_max, animated=True)
    ax2.set_title("True Value Grid (V)", fontsize=12)
    fig.colorbar(im2, ax=ax2, fraction=0.046, pad=0.04)

    # 3. Predicted Value Grid
    im3 = ax3.imshow(v_pred[0], cmap="RdBu_r", vmin=v_min, vmax=v_max, animated=True)
    ax3.set_title("Predicted Value Grid (v)", fontsize=12)
    fig.colorbar(im3, ax=ax3, fraction=0.046, pad=0.04)

    # 4. Signed Value Error Grid (v - V)
    im4 = ax4.imshow(signed_error[0], cmap="RdBu_r", animated=True, norm=colors.SymLogNorm(linthresh=0.01, vmin=-v_max, vmax=v_max, base=10))
    ax4.set_title("Signed Value Error (v - V)", fontsize=12)
    fig.colorbar(im4, ax=ax4, fraction=0.046, pad=0.04)
    


    frame_text = fig.text(0.5, 0.01, f"Update 1 / {num_updates}", ha="center", fontsize=11, fontweight='bold')
    plt.tight_layout()

    def update(frame):
        im1.set_array(state_dist[frame])
        im1.set_clim(np.min(state_dist[frame]), np.max(state_dist[frame]))

        im2.set_array(v_true[frame])
        im3.set_array(v_pred[frame])
        im4.set_array(signed_error[frame])
        frame_text.set_text(f"Update {frame + 1} / {num_updates}")
        return im1, im2, im3, im4, frame_text

    ani = animation.FuncAnimation(fig, update, frames=num_updates, interval=1000 // fps, blit=False)

    if save_gif:
        out_dir = os.path.dirname(gif_path)
        if out_dir:
            os.makedirs(out_dir, exist_ok=True)
        ani.save(gif_path, writer='pillow', fps=fps)
        print(f"[{run_name}] Saved GIF video to: {gif_path}")

    if display_inline:
        display(HTML(ani.to_jshtml()))

    plt.close(fig)
    return ani

## 1. TD Run Visualization

In [3]:
config, metrics = load_run_data_from_path('../' + RUNS_CONFIG["TD"]['path'])

In [4]:
# Generate GIF animation for TD run
ani_td = generate_and_save_grid_gif(RUNS_CONFIG["TD"], save_gif=True, fps=5)

[TD Run] Saved GIF video to: figures/td_run_grid_vis.gif


## 2. MC Run Visualization

In [5]:
# Generate GIF animation for MC run
ani_mc = generate_and_save_grid_gif(RUNS_CONFIG["MC"], save_gif=True, fps=5)

[MC Run] Saved GIF video to: figures/mc_run_grid_vis.gif


In [6]:
ani_mc = generate_and_save_grid_gif(RUNS_CONFIG["MC_seed_2"], save_gif=True, fps=5)

[MC Run 2] Saved GIF video to: figures/mc_run2_grid_vis.gif


## 3. Exact E Run (Seed 1) Visualization

In [ ]:
ani_e_seed1 = generate_and_save_grid_gif(RUNS_CONFIG["E_seed1"], save_gif=True, fps=5)

[Exact E Run (Seed 1)] Saved GIF video to: figures/E_seed_1_vis.gif


In [ ]:
# This is a failing example of E optimization.
# The LR is high leading to constant everywhere value predictions. Stablizies on the random policy.


## 4. Exact E Run (Seed 2) Visualization

In [ ]:
# This is a running example of E optimization.
# LR = ACTOR_LR = 0.0003
ani_e_seed2 = generate_and_save_grid_gif(RUNS_CONFIG["E_seed2"], save_gif=True, fps=5)

In [ ]:

ani_e_lambda = generate_and_save_grid_gif(RUNS_CONFIG["E_lambda"], save_gif=True, fps=5)